# 3 · Filtering & highlighting

Show only the road types you care about, and highlight a selection on top of the map.

In [1]:
import pathlib
import geopandas as gpd
import roadstyle as rs

# A GeoDataFrame of road edges. roadstyle only needs a *road-class* column (default "highway")
# and line geometry in any CRS — it reprojects to web coordinates (EPSG:4326) for you.
edges = gpd.read_file(pathlib.Path("data") / "sodermalm_edges.gpkg")
print(f"{len(edges):,} edges, CRS {edges.crs}")
edges[[c for c in edges.columns if c != edges.geometry.name]].head(3)


4,563 edges, CRS EPSG:4326


ERROR 1: PROJ: proj_create_from_database: Open of /home/kaveh/miniconda3/envs/roadstyle/share/proj failed


,edge_id,osm_id,edge_ref,highway,name,lanes,oneway,maxspeed_kmh,length_m,tunnel,bridge,layer
0,6379011699359957301,4080398,4080398#1f,residential,Nackagatan,1,False,30.0,61.872971,NaN,NaN,NaN
1,4910696379820034244,4080398,4080398#3f,residential,Nackagatan,1,False,30.0,34.481152,NaN,NaN,NaN
2,6981489206416339981,4080984,4080984#2f,residential,Högalidsgatan,1,False,30.0,34.356903,NaN,NaN,NaN


### What road types are present?

In [2]:
sorted(rs.highway_types(edges))

['living_street',
 'primary',
 'residential',
 'secondary',
 'service',
 'tertiary',
 'trunk',
 'unclassified']

### Keep / drop types with `include` / `exclude`
`match_links=True` (default) keeps `*_link` ramps together with their parent type.

In [3]:
rs.render_edges(edges, include=["motorway", "trunk", "primary"], basemap="dark_matter", compress=True)

In [4]:
rs.render_edges(edges, exclude=["service", "footway", "path", "cycleway"], compress=True)

## Pre-selecting edges (folium backend)
Pass `selected=` a sub-frame to spotlight those edges with the neon selection style. On the default web backend, selection is interactive instead: click any road for its popup and highlight.

In [5]:
sel = edges[edges["highway"] == "secondary"]
# `selected=` pre-highlights edges on the folium backend (neon glow). The web backend
# doesn't take it — there you click a road to select it (popup + highlight built in).
rs.render_edges(edges, backend="folium", basemap="dark_matter", selected=sel)

## Click read-out: floating popup, side panel, or your own UI

By default a click opens a **popup** with the curated fields. Two alternatives:

- `road_popup="panel"` — a **docked side panel** (bottom-right): never covers the road you clicked, stays put in tilted 3D views, shows the same formatted fields.
- build your own: every click dispatches a `rs:select` CustomEvent with `event.detail.properties` (and `rs:deselect` on clear) — set `road_popup=False` and route the data into any sidebar or dashboard.

In [6]:
# click any road: the read-out docks bottom-right instead of floating over the map
rs.render_edges(edges, basemap="dark_matter", road_popup="panel", compress=True)

## Drive the map from JavaScript (`window.rs*`)

Every in-map control is a thin UI over a global JS function — anything you can click, your own HTML/JS can call. Each setter updates the map, keeps the built-in control in sync, and fires a `rs:*` CustomEvent on `document`:

| call | does | event |
|---|---|---|
| `rsSetBasemap("blank")` | switch base map (key, label, or index) | `rs:basemapchange` |
| `rsSetClasses(["primary","secondary"])` | show exactly these road classes | `rs:filterchange` |
| `rsSetColorField("Traffic")` | switch the colour layer (`color_options`) | `rs:colorchange` |
| `rsSetOverlay("Zones", false)` | hide/show one overlay | `rs:overlaychange` |
| `rsSetView3D(true)` | tilt to the settings' 3D pitch / back to flat | `rs:viewchange` |
| `rsSelect(id)` / `rsDeselect()` | select an edge exactly like a click / clear | `rs:select` / `rs:deselect` |
| `map.easeTo({pitch: 60})` | free-form camera — `window.map` is the MapLibre `Map` | — |

And the baked features are a **queryable table**: `rsQuery(p => …)` evaluates a predicate (a WHERE clause, written in JS) over every edge's columns and returns an **id set**; then independent verbs act on that set:

| call | does |
|---|---|
| `ids = rsQuery(p => p.maxspeed_kmh >= 50)` | → ids of the matching edges |
| `rsFilter(ids)` / `rsFilter(null)` | show only these edges / reset |
| `rsColor(ids, "#ff00aa")` / `rsColor(null)` | paint the set one colour / reset |
| `rsHighlight(ids)` / `rsHighlight([])` | selection glow / clear |
| `rsGetProps(ids)` | the rows behind the ids — build a table from them |
| `rsFocus(ids)` | fly the camera to fit the set (or a single id) |

Enumerate what's available with `RS_BASEMAPS`, `RS_CLASSES`, `RS_COLOR_OPTIONS`, `RS_OVERLAYS`. The setters work even with the built-in controls hidden (`basemap_switcher=False`, `filter_control=False`) — pass an explicit `basemaps=[...]` list to keep all entries addressable. Below: a saved map extended with plain HTML buttons — the "Fast roads" query recolours its id set and lists it in a small table whose **rows are clickable** (`rsSelect`), closing the loop: query → table → click a row → that road is selected on the map.

> For a bigger head start, two ready-made sidebars ship **with the library**, built purely on this API: `rs.render_dashboard(edges).save("dashboard.html")` — a full sidebar dashboard (query box with SQL-style syntax, verb buttons, a clickable table that selects **and flies to** the road, detail panel, base-map and colour-by selects) — and `rs.render_report(edges)`, a stats panel (KPI cards, legend, filter, search). `rs.sidebar_html("dashboard")` returns the fragment to reshape; the same templates live in the repo's **`ui/`** folder.

In [7]:
# your own buttons over a saved map: no dropdown/panel, just the rs* API + plain HTML/JS
out = pathlib.Path("output"); out.mkdir(exist_ok=True)
m = rs.render_edges(edges, basemap="voyager", basemaps=["voyager", "dark_matter", "blank"],
                    basemap_switcher=False, filter_control=False, compress=True)
extra = """
<script>
function fastRoads(){
  const ids = rsQuery(p => p.maxspeed_kmh >= 50);           // the WHERE clause
  rsColor(ids, '#ff00aa'); rsHighlight(ids);                // act on the id set
  const props = rsGetProps(ids), seen = new Set();          // ...and table it
  const rows = ids.map((id, k) => ({id, p: props[k]}))
    .filter(r => r.p.name && !seen.has(r.p.name) && seen.add(r.p.name)).slice(0, 10);
  const el = document.getElementById('tbl'); el.style.display = 'block';
  el.innerHTML = '<b>maxspeed &ge; 50</b>' + rows.map(r =>
    '<div><a href="#" data-id="' + r.id + '">' + r.p.name + '</a> &mdash; ' +
    r.p.maxspeed_kmh + ' km/h</div>').join('');
  el.querySelectorAll('a').forEach(a => a.onclick = e => {   // row click -> select on the map
    e.preventDefault(); rsSelect(+a.dataset.id); });
}
function resetAll(){
  rsSetClasses(RS_CLASSES); rsColor(null); rsHighlight([]); rsDeselect();
  document.getElementById('tbl').style.display = 'none';
}
</script>
<div style="position:absolute;top:10px;left:10px;z-index:9;display:flex;gap:6px">
  <button onclick="rsSetBasemap('blank')">No base layer</button>
  <button onclick="rsSetClasses(['primary','secondary'])">Majors only</button>
  <button onclick="rsSetView3D(map.getPitch() < 5)">2D/3D</button>
  <button onclick="fastRoads()">Fast roads</button>
  <button onclick="resetAll()">Reset</button>
</div>
<div id="tbl" style="display:none;position:absolute;bottom:34px;left:10px;z-index:9;
  background:#fff;padding:8px 12px;border-radius:5px;font:12px system-ui;
  box-shadow:0 1px 4px rgba(0,0,0,.3)"></div>
</body>"""
(out / "scripted_map.html").write_text(m.html.replace("</body>", extra))
print("open", (out / "scripted_map.html").resolve())

open /home/kaveh/projects/roadstyle/notebooks/output/scripted_map.html
